In [0]:
# Criando o banco de dados da camada Silver
spark.sql("CREATE DATABASE IF NOT EXISTS silver")

DataFrame[]

In [0]:
from pyspark.sql.functions import col, trim, upper, regexp_replace, when, coalesce, year, row_number, expr
from pyspark.sql.window import Window

# Lê os dados brutos da camada Bronze
df_info = spark.read.table("bronze.tb_movies_info")

# 1. Renomear as colunas para o português
df_info = df_info.withColumnRenamed("id", "id_filme") \
                 .withColumnRenamed("title", "titulo") \
                 .withColumnRenamed("original_title", "titulo_original") \
                 .withColumnRenamed("release_date", "data_lancamento") \
                 .withColumnRenamed("runtime", "duracao_minutos") \
                 .withColumnRenamed("original_language", "idioma_original") \
                 .withColumnRenamed("status", "status_filme") \
                 .withColumnRenamed("overview", "sinopse") \
                 .withColumnRenamed("tagline", "frase_divulgacao")

# 2. Limpeza e Tradução do Status
# Normaliza: remove hifens indesejados e padroniza tudo para letras maiúsculas
df_info = df_info.withColumn("status_filme", upper(trim(regexp_replace(col("status_filme"), "-", ""))))

# Aplica a tradução. O que for corrompido vira "Não Informado"
df_info = df_info.withColumn("status_filme", 
    when(col("status_filme") == "RELEASED", "Lançado")
    .when(col("status_filme") == "POST PRODUCTION", "Pós-Produção")
    .when(col("status_filme") == "IN PRODUCTION", "Em Produção")
    .when(col("status_filme") == "PLANNED", "Planejado")
    .when(col("status_filme") == "RUMORED", "Rumores")
    .when(col("status_filme") == "CANCELED", "Cancelado")
    .otherwise("Não Informado")
)

# 3. Tratamento de Data Multi-Formato 
# O try_to_date tolera erros sem quebrar o pipeline.
# Ele testa vários formatos na ordem até encontrar um que funcione.
df_info = df_info.withColumn("data_lancamento", 
    coalesce(
        expr("try_to_date(data_lancamento, 'yyyy-MM-dd')"),
        expr("try_to_date(data_lancamento, 'MM-dd-yyyy')"),  
        expr("try_to_date(data_lancamento, 'dd/MM/yyyy')"),
        expr("try_to_date(data_lancamento, 'MM/dd/yyyy')")
    )
)
# Deriva o ano de lançamento
df_info = df_info.withColumn("ano_lancamento", year(col("data_lancamento")))

# 4. Deduplicação por Filme
# Agrupa por id_filme e ordena pela data de ingestão mais recente
window_spec = Window.partitionBy("id_filme").orderBy(col("ingestion_datetime").desc())
df_info = df_info.withColumn("num_linha", row_number().over(window_spec)) \
                 .filter(col("num_linha") == 1) \
                 .drop("num_linha")

# 5. Salva na camada Silver e exibe o resultado
df_info.write.format("delta").mode("overwrite").saveAsTable("silver.tb_info_filmes")

print("Tabela silver.tb_info_filmes criada com sucesso!")
display(df_info)

Tabela silver.tb_info_filmes criada com sucesso!


id_filme,tconst,titulo,titulo_original,idioma_original,data_lancamento,duracao_minutos,status_filme,sinopse,frase_divulgacao,ingestion_datetime,ano_lancamento
14564,tt0498381,Rings,Rings,en,2017-02-01,102,Lançado,"\Julia becomes worried about her boyfriend Holt when he explores the dark urban legend of a mysterious videotape said to kill the watcher seven days after viewing. She sacrifices herself to save her boyfriend and in doing so makes a horrifying discovery: there is a \""\""movie within the movie\""\"" that no one has ever seen before.\""""",First you watch it. Then you die.,2026-10-05T21:19:34.117Z,2017
32471,tt1587420,Mixtape,Mixtape,en,2021-12-03,94,Lançado,null,null,2026-10-05T21:19:34.117Z,2021
38258,tt0093119,Grizzly II: Revenge,Grizzly II: Revenge,en,2020-02-17,74,Lançado,\All hell breaks loose when a giant grizzly,reacting to the slaughter of her cubs by poachers,2026-10-05T21:19:34.117Z,2020
38492,tt0215569,Billy Joel - Live at Yankee Stadium,Billy Joel Live at Yankee Stadium,en,2022-06-22,86,Lançado,Billy Joel plays his greatest hits in the Big Apple.,null,2026-10-05T21:19:34.117Z,2022
38700,tt1502397,Bad Boys for Life,Bad Boys for Life,en,2020-01-15,124,Lançado,"Marcus and Mike are forced to confront new threats, career changes, and midlife crises as they join the newly created elite team AMMO of the Miami police department to take down the ruthless Armando Armas, the vicious leader of a Miami drug cartel.",Ride together. Die together.,2026-10-05T21:19:34.117Z,2020
42018,tt0090907,The Horse Thief,盗马贼,zh,2019-03-19,88,Lançado,"Devout Buddhists, Norbu and Dolma live with their young son Tashi in a clan in Tibet. Norbu is a highwayman. After Norbu is charged with stealing from the temple, he and his family are banished. Impoverished and marginalized, they can do little when their beloved son becomes ill. Tashi dies of a fever. After a second son is born, Norbu focuses his every action on keeping this child alive, seeking re-admission to the clan for his wife and child, then risking all to save them from isolation and starvation in winter.",null,2026-10-05T21:19:34.117Z,2019
42330,tt10443316,Monkey Magic,大闹西游,zh,2018-09-22,66,Lançado,"Dearth Voyd, the ruler of the dark side of the universe, wants to turn the human world into a place of violence and evil!! However, a huge meteor falls upon Flower-Fruit mountain giving birth to Kongo, a monkey made of stone! Kongo, now sets out on his quest to fight evil and restore order to a desperate land. Episodes 1-3",null,2026-10-05T21:19:34.117Z,2018
43074,tt1289401,Ghostbusters,Ghostbusters,en,2016-07-14,117,Lançado,"Following a ghost invasion of Manhattan, paranormal enthusiasts Erin Gilbert and Abby Yates, nuclear engineer Jillian Holtzmann, and subway worker Patty Tolan band together to stop the otherworldly threat.",Who You Gonna Call?,2026-10-05T21:19:34.117Z,2016
45033,tt1202339,20 Seconds of Joy,20 Seconds of Joy,de,2018-01-01,60,Lançado,"Traces the story of an extreme athlete, past and present; but also explores the psychology behind life, death, risk and the confrontation of fear.",null,2026-10-05T21:19:34.117Z,2018
46983,tt0051471,The Song of Styrene,Le Chant du styrène,fr,2022-05-23,13,Lançado,Le chant du Styrène is a 1958 French documentary film directed by Alain Resnais. The film was an order by French industrial group Pechiney to highlight the merits of plastics.,null,2026-10-05T21:19:34.117Z,2022


In [0]:
from pyspark.sql.functions import col, when, regexp_replace, trim, lit, round
from pyspark.sql.types import DecimalType

# 1. Obter a cotação mais recente do dólar da tabela Bronze
# Ler a tabela, ordenar pela data mais recente e extrair o primeiro valor de compra
df_cotacao = spark.read.table("bronze.tb_cotacao_dolar")
taxa_dolar = df_cotacao.orderBy(col("dataHoraCotacao").desc()).select("cotacaoCompra").first()[0]

# 2. Ler os dados financeiros brutos
df_fin = spark.read.table("bronze.tb_movies_financials")

# Renomear as colunas originais
df_fin = df_fin.withColumnRenamed("id", "id_filme") \
               .withColumnRenamed("budget", "orcamento_usd") \
               .withColumnRenamed("revenue", "receita_usd")

# 3. Limpeza, Higienização e Validação das Métricas Financeiras
for coluna in ["orcamento_usd", "receita_usd"]:
    
    # Regra A: Tratar valores textuais de ausência como nulos ANTES da conversão
    df_fin = df_fin.withColumn(coluna, 
        when(trim(col(coluna)).isin("Unknown", "Não Informado", "N/A", ""), None)
        .otherwise(col(coluna))
    )
    
    # Regra B: Higienizar colunas para remover moedas e separadores de milhar
    # A expressão regular r"[^\d\.]" mantém EXCLUSIVAMENTE números (0-9) e o ponto decimal (.)
    df_fin = df_fin.withColumn(coluna, regexp_replace(col(coluna), r"[^\d\.]", ""))
    
    # Regra C: Converter para decimal (18,2)
    df_fin = df_fin.withColumn(coluna, col(coluna).cast(DecimalType(18,2)))
    
    # Regra D: Garantir que valores zerados ou negativos sejam nulos
    df_fin = df_fin.withColumn(coluna, 
        when(col(coluna) <= 0, None)
        .otherwise(col(coluna))
    )

# 4. Calcular valores em Reais (BRL) usando a cotação isolada no passo 1
df_fin = df_fin.withColumn("orcamento_brl", round(col("orcamento_usd") * lit(taxa_dolar), 2).cast(DecimalType(18,2))) \
               .withColumn("receita_brl", round(col("receita_usd") * lit(taxa_dolar), 2).cast(DecimalType(18,2)))

# 5. Derivar Lucro e Margem de Lucro
# Como os valores negativos/zerados viraram NULL no Passo 3, o PySpark retorna NULL automaticamente 
# em operações matemáticas com valores vazios, evitando que a conta quebre.
df_fin = df_fin.withColumn("lucro_usd", (col("receita_usd") - col("orcamento_usd")).cast(DecimalType(18,2))) \
               .withColumn("lucro_brl", (col("receita_brl") - col("orcamento_brl")).cast(DecimalType(18,2)))

# Evitar divisão por zero: garantido porque receitas zeradas já são NULL. 
# Margem = (Lucro / Receita) * 100
df_fin = df_fin.withColumn("margem_lucro_percentual", 
    round((col("lucro_usd") / col("receita_usd")) * 100, 2).cast(DecimalType(18,2))
)

# 6. Salvar na camada Silver e exibir o resultado
df_fin.write.format("delta").mode("overwrite").saveAsTable("silver.tb_financeiro_filmes")

print(f"Tabela silver.tb_financeiro_filmes criada! Conversão BRL aplicada: R$ {taxa_dolar:.4f}")
display(df_fin)

Tabela silver.tb_financeiro_filmes criada! Conversão BRL aplicada: R$ 4.9853


id_filme,orcamento_usd,receita_usd,ingestion_datetime,orcamento_brl,receita_brl,lucro_usd,lucro_brl,margem_lucro_percentual
293660,58000000.00,null,2026-10-05T21:19:43.138Z,289147400.00,null,null,null,null
299536,300000000.00,2052415039.00,2026-10-05T21:19:43.138Z,1495590000.00,10231904693.93,1752415039.00,8736314693.93,85.38
299534,356000000.00,2800000000.00,2026-10-05T21:19:43.138Z,1774766800.00,13958840000.00,2444000000.00,12184073200.00,87.29
475557,55000000.00,1074458282.00,2026-10-05T21:19:43.138Z,274191500.00,5356496873.25,1019458282.00,5082305373.25,94.88
271110,250000000.00,null,2026-10-05T21:19:43.138Z,1246325000.00,null,null,null,null
284054,200000000.00,1349926083.00,2026-10-05T21:19:43.138Z,997060000.00,6729786501.58,1149926083.00,5732726501.58,85.18
284052,180000000.00,676343174.00,2026-10-05T21:19:43.138Z,897354000.00,3371773625.34,496343174.00,2474419625.34,73.39
315635,175000000.00,880166924.00,2026-10-05T21:19:43.138Z,872427500.00,4387896166.22,705166924.00,3515468666.22,80.12
283995,200000000.00,863756051.00,2026-10-05T21:19:43.138Z,997060000.00,4306083041.05,663756051.00,3309023041.05,76.85
297761,175000000.00,746846894.00,2026-10-05T21:19:43.138Z,872427500.00,3723255820.66,571846894.00,2850828320.66,76.57


In [0]:
from pyspark.sql.functions import col, when, regexp_replace, expr

# 1. Ler os dados brutos da tabela de métricas
df_metrics = spark.read.table("bronze.tb_movies_metrics")

# 2. Renomear as colunas conforme o mapeamento exigido
df_metrics = df_metrics.withColumnRenamed("id", "id_filme") \
                       .withColumnRenamed("popularity", "popularidade") \
                       .withColumnRenamed("vote_average", "nota_media_tmdb") \
                       .withColumnRenamed("vote_count", "qtd_votos_tmdb") \
                       .withColumnRenamed("averageRating", "nota_media_imdb") \
                       .withColumnRenamed("numVotes", "qtd_votos_imdb")

# 3. Limpeza de formatação da coluna popularidade
# Trocar vírgulas por pontos (para padronizar o decimal) e remover caracteres que não sejam números, pontos ou sinal de menos
df_metrics = df_metrics.withColumn("popularidade", regexp_replace(col("popularidade"), ",", "."))
df_metrics = df_metrics.withColumn("popularidade", regexp_replace(col("popularidade"), r"[^\d\.-]", ""))

# 4. Conversão de tipagem segura (Safe Cast) contra Column Shift
# O try_cast converte valores válidos e transforma textos incompatíveis em NULL automaticamente
df_metrics = df_metrics.withColumn("popularidade", expr("try_cast(popularidade as double)")) \
                       .withColumn("nota_media_tmdb", expr("try_cast(nota_media_tmdb as double)")) \
                       .withColumn("nota_media_imdb", expr("try_cast(nota_media_imdb as double)")) \
                       .withColumn("qtd_votos_tmdb", expr("try_cast(qtd_votos_tmdb as int)")) \
                       .withColumn("qtd_votos_imdb", expr("try_cast(qtd_votos_imdb as int)"))

# 5. Tratamento de limites numéricos de negócio
# Anular notas que estejam fora do intervalo de 0 a 10
for coluna_nota in ["nota_media_tmdb", "nota_media_imdb"]:
    df_metrics = df_metrics.withColumn(coluna_nota, 
        when((col(coluna_nota) < 0) | (col(coluna_nota) > 10), None)
        .otherwise(col(coluna_nota))
    )

# Anular contagens de votos e popularidade que apresentem valores negativos
for coluna_positiva in ["popularidade", "qtd_votos_tmdb", "qtd_votos_imdb"]:
    df_metrics = df_metrics.withColumn(coluna_positiva, 
        when(col(coluna_positiva) < 0, None)
        .otherwise(col(coluna_positiva))
    )

# 6. Salvar na camada Silver e exibir o resultado
df_metrics.write.format("delta").mode("overwrite").saveAsTable("silver.tb_metricas_engajamento")

print("Tabela silver.tb_metricas_engajamento higienizada e criada com sucesso!")
display(df_metrics)

Tabela silver.tb_metricas_engajamento higienizada e criada com sucesso!


id_filme,popularidade,nota_media_tmdb,qtd_votos_tmdb,nota_media_imdb,qtd_votos_imdb,ingestion_datetime
293660,72.735,7.606,28894,8.0,1270339,2026-10-05T21:19:47.932Z
299536,154.34,8.255,27713,8.4,1406782,2026-10-05T21:19:47.932Z
299534,91.756,8.263,23857,8.4,1484150,2026-10-05T21:19:47.932Z
475557,54.522,8.168,23425,8.3,1723035,2026-10-05T21:19:47.932Z
271110,70.741,7.4,21541,7.8,947222,2026-10-05T21:19:47.932Z
284054,43.665,7.39,null,7.3,924922,2026-10-05T21:19:47.932Z
284052,70.535,7.427,20935,7.5,895880,2026-10-05T21:19:47.932Z
315635,65.88,7.345,20507,7.4,835116,2026-10-05T21:19:47.932Z
283995,67.553,7.624,20353,7.6,844767,2026-10-05T21:19:47.932Z
297761,35.356,5.909,20097,5.9,null,2026-10-05T21:19:47.932Z


In [0]:
from pyspark.sql.functions import col, when, trim

# 1. Ler os dados da tabela de avaliações na camada Bronze
df_reviews = spark.read.table("bronze.tb_movies_reviews")

# 2. Renomear as colunas conforme o mapeamento do projeto
df_reviews = df_reviews.withColumnRenamed("id", "id_filme") \
                       .withColumnRenamed("nome", "nome_usuario") \
                       .withColumnRenamed("nota", "nota_usuario") \
                       .withColumnRenamed("comentario", "comentario_usuario")

# 3. Remover registros integralmente duplicados
# O dropDuplicates valida se a combinação exata de todas as colunas listadas já existe
df_reviews = df_reviews.dropDuplicates(["id_filme", "nome_usuario", "nota_usuario", "comentario_usuario"])

# 4. Aplicar a regra de negócio da nota (escala de 0 a 10)
# Converte para número e descarta valores fora do limite
df_reviews = df_reviews.withColumn("nota_usuario", col("nota_usuario").cast("double"))
df_reviews = df_reviews.withColumn("nota_usuario", 
    when((col("nota_usuario") < 0) | (col("nota_usuario") > 10), None)
    .otherwise(col("nota_usuario"))
)

# 5. Tratar comentários não preenchidos ou apenas com espaços em branco
# A função trim() remove espaços nas extremidades. Se sobrar "", significa que era apenas espaço ou estava vazio.
df_reviews = df_reviews.withColumn("comentario_usuario", 
    when(col("comentario_usuario").isNull() | (trim(col("comentario_usuario")) == ""), "Sem comentário")
    .otherwise(col("comentario_usuario"))
)

# 6. Salvar na camada Silver e exibir o resultado
df_reviews.write.format("delta").mode("overwrite").saveAsTable("silver.tb_avaliacoes_usuarios")

print("Tabela silver.tb_avaliacoes_usuarios criada e higienizada com sucesso!")
display(df_reviews)

Tabela silver.tb_avaliacoes_usuarios criada e higienizada com sucesso!


id_filme,nome_usuario,nota_usuario,comentario_usuario,ingestion_datetime
442113,Mariana Cardoso 277,4.4,Sem comentário,2026-10-05T21:19:57.678Z
637007,Lucas Reis 602,3.9,Sem comentário,2026-10-05T21:19:57.678Z
449479,Sérgio Freitas,0.7,Péssimo em todos os sentidos.,2026-10-05T21:19:57.678Z
413036,Gabriela Monteiro 401,7.5,Sem comentário,2026-10-05T21:19:57.678Z
528480,Leonardo Monteiro,6.3,Assisti até o final mas não me marcou.,2026-10-05T21:19:57.678Z
387727,Maria Alves 707,8.2,"Gostei bastante, recomendo.",2026-10-05T21:19:57.678Z
1032506,Amanda Castro 242,4.7,"Fraco, não recomendo.",2026-10-05T21:19:57.678Z
446554,Sandra Rodrigues 736,6.5,Assisti até o final mas não me marcou.,2026-10-05T21:19:57.678Z
569916,Camila Lima 489,8.2,Muito bom! Vale a pena assistir.,2026-10-05T21:19:57.678Z
864552,Roberto Almeida 555,9.3,"Obra-prima do cinema, simplesmente espetacular.",2026-10-05T21:19:57.678Z


In [0]:
from pyspark.sql.functions import col, split, explode, trim, regexp_replace, length

# 1. Ler os dados da tabela que contém as tags e gêneros na camada Bronze
df_credits = spark.read.table("bronze.tb_credits_and_tags")

# Selecionar apenas o ID do filme e a coluna de gêneros
df_generos = df_credits.select(
    col("id").alias("id_filme"), 
    col("genres")
)

# 2. Tratar a inconsistência de separadores
# O regex r"[;\|]" encontra tanto ponto e vírgula quanto a barra vertical, substituindo por vírgula
df_generos = df_generos.withColumn("genres", regexp_replace(col("genres"), r"[;\|]", ","))

# 3. Desmembrar (Split) e Explodir (Explode) a coluna
df_generos = df_generos.withColumn("genero", explode(split(col("genres"), ",")))

# 4. Limpeza de resíduos e anomalias de Column Shift
df_generos = df_generos.withColumn("genero", trim(col("genero")))

df_generos = df_generos.filter(
    (col("genero") != "") & 
    (col("genero").isNotNull()) & 
    (~col("genero").rlike(r"\d")) & 
    (length(col("genero")) <= 30)
)

# 5. Remover a coluna original e garantir a unicidade
df_generos = df_generos.select("id_filme", "genero").dropDuplicates()

# 6. Salvar na camada Silver e exibir o resultado
df_generos.write.format("delta").mode("overwrite").saveAsTable("silver.tb_generos")

print("Tabela silver.tb_generos criada, explodida e higienizada com sucesso!")
display(df_generos)

Tabela silver.tb_generos criada, explodida e higienizada com sucesso!


id_filme,genero
299534,Action
297761,Action
284053,Adventure
429617,Science Fiction
353486,Fantasy
274870,Science Fiction
127380,Family
398818,Romance
166426,Action
351286,Thriller


In [0]:
from pyspark.sql.functions import col, lit, split, explode, trim, initcap, regexp_replace

# 1. Ler os dados originais
df_credits = spark.read.table("bronze.tb_credits_and_tags")

# Mapeamento das regras de negócio
mapeamento_entidades = {
    "cast": "Ator",
    "directors": "Diretor",
    "writers": "Roteirista",
    "production_companies": "Produtora"
}

dfs_entidades = []

# 2. Processar cada coluna individualmente
for coluna_origem, tipo_resultante in mapeamento_entidades.items():
    
    # Isolar o ID do filme e a coluna da vez
    df_temp = df_credits.select(
        col("id").alias("id_filme"),
        col(coluna_origem)
    )
    
    # Padronizar separadores caso existam sujeiras (barras ou ponto e vírgula)
    df_temp = df_temp.withColumn(coluna_origem, regexp_replace(col(coluna_origem), r"[;\|]", ","))
    
    # Desmembrar e explodir para gerar uma linha por pessoa/empresa
    df_temp = df_temp.withColumn("nome_entidade", explode(split(col(coluna_origem), ",")))
    
    # 3. Limpeza, Capitalização e Tipagem
    # Remove espaços, aplica Iniciais Maiúsculas e anexa o tipo de entidade resultante
    df_temp = df_temp.withColumn("nome_entidade", initcap(trim(col("nome_entidade")))) \
                     .withColumn("tipo_entidade", lit(tipo_resultante))
                     
    # Descartar linhas que ficaram vazias após o split
    df_temp = df_temp.filter((col("nome_entidade") != "") & (col("nome_entidade").isNotNull()))
    
    # Selecionar apenas as colunas finais padronizadas
    df_temp = df_temp.select("id_filme", "nome_entidade", "tipo_entidade")
    
    # Guardar na lista para empilhar depois
    dfs_entidades.append(df_temp)

# 4. Consolidar os 4 DataFrames em um único modelo (Empilhamento)
df_pessoas_empresas = dfs_entidades[0].union(dfs_entidades[1]) \
                                      .union(dfs_entidades[2]) \
                                      .union(dfs_entidades[3])

# 5. Eliminar registros duplicados
df_pessoas_empresas = df_pessoas_empresas.dropDuplicates()

# 6. Salvar na camada Silver e exibir o resultado
df_pessoas_empresas.write.format("delta").mode("overwrite").saveAsTable("silver.tb_pessoas_empresas")

print("Tabela silver.tb_pessoas_empresas unificada e padronizada com sucesso!")
display(df_pessoas_empresas)

Tabela silver.tb_pessoas_empresas unificada e padronizada com sucesso!


id_filme,nome_entidade,tipo_entidade
299536,Chris Hemsworth,Ator
475557,Frances Conroy,Ator
634649,Tom Holland,Ator
209112,Jeremy Irons,Ator
329865,Julia Scarlett Dan,Ator
381288,Anya Taylor-joy,Ator
419430,Caleb Landry Jones,Ator
424694,Ben Hardy,Ator
335983,Malcolm C. Murray,Ator
429617,Samuel L. Jackson,Ator


In [0]:
from pyspark.sql.functions import col, to_date, explode, sequence, last
from pyspark.sql.window import Window

# 1. Ler os dados da cotação na camada Bronze
df_cotacao = spark.read.table("bronze.tb_cotacao_dolar")

# Converter a dataHora para apenas Data (YYYY-MM-DD) para facilitar o cruzamento
df_cotacao = df_cotacao.withColumn("data_original", to_date(col("dataHoraCotacao")))

# 2. Descobrir a data inicial e final dinamicamente
min_date, max_date = df_cotacao.selectExpr("min(data_original)", "max(data_original)").first()

# 3. Gerar a Série Temporal Contínua
# A função sequence cria uma lista com todos os dias possíveis entre as duas datas
df_calendario = spark.sql(f"SELECT explode(sequence(to_date('{min_date}'), to_date('{max_date}'))) as data_referencia")

# 4. Fazer o Join com os dados reais
# Juntamos o calendário perfeito (todas as datas) com a base do BCB. 
df_completo = df_calendario.join(df_cotacao, df_calendario.data_referencia == df_cotacao.data_original, "left")

# 5. Aplicar o Forward Fill (Preenchimento para frente) apenas na coluna existente
janela = Window.orderBy("data_referencia").rowsBetween(Window.unboundedPreceding, 0)

df_silver_cotacao = df_completo.select(
    col("data_referencia"),
    last("cotacaoCompra", ignorenulls=True).over(janela).alias("cotacaoCompra")
)

# 6. Salvar na camada Silver e exibir
df_silver_cotacao.write.format("delta").mode("overwrite").saveAsTable("silver.tb_cotacao_dolar")

print("Tabela silver.tb_cotacao_dolar criada com série temporal contínua e Forward Fill com sucesso!")
display(df_silver_cotacao)

/databricks/python/lib/python3.12/site-packages/pyspark/sql/connect/expressions.py:1155: UserWarning: WARN WindowExpression: No Partition Defined for Window operation! Moving all data to a single partition, this can cause serious performance degradation.
  warnings.warn(


Tabela silver.tb_cotacao_dolar criada com série temporal contínua e Forward Fill com sucesso!


data_referencia,cotacaoCompra
2026-09-28,5.2126
2026-09-29,5.2198
2026-09-30,5.1803
2026-10-01,5.2073
2026-10-02,5.2232
2026-10-03,5.2232
2026-10-04,5.2232
2026-10-05,4.9853
